WARNING:
----THIS NOTEBOOK IS FAR BEHIND pl.py, since I don't use the notebook anymore 
---THE INTERACTIVE PLOTS (TO CREATE CROPLIM FOR rgname, AND TO PLOT ROIS AT THE END) HAVE STOPPED WORKING SUDDENLY, NOT SURE WHY
---BESIDES THIS THE NOTEBOOK WORKS 
---IF YOU'RE USING ANY rgname OTHER THAN 'fullfov' YOU NEED TO HAVE THE CROPLIM NPY FILES ALREADY SAVED TO RUN THIS ENTIRE NOTEBOOK
---THE PLOTS IN THE PY VERSION OF THE PIPELINE WORK FINE, SO YOU CAN CREATE AND SAVE CROPLIM NPY FILES THAT WAY   

NOTEBOOK DIFFERS FROM PY FILES IN THE IMPORTS (CELL TITLE "SETUP") AND THE FOV SELECTION CODE (CELL TITLE "CROPPING FUNCTIONS") and not looping over recordings and rgname, and also using some uses plotting functions

In [ ]:
#@title setup

virtenv = 'caiman' # 'deepcad' for denoising or 'caiman' for everything else, this just changes imports during setup

import sys
IN_COLAB = 'google.colab' in sys.modules

if IN_COLAB:

  from google.colab import drive
  drive.mount('/content/drive')

  !pip install scanimage-tiff-reader
  !pip install mat73
  !pip install natsort
  !pip install dash
  !pip install jupyter-dash


from ScanImageTiffReader import ScanImageTiffReader
import mat73
from natsort import natsorted

import glob
import os
import re
import fnmatch
import logging

import shutil
import datetime
from ast import literal_eval

import numpy as np
from numpy.core.records import fromarrays
import random

from tqdm import tqdm
import scipy
from scipy import signal
import scipy.io as sio

from tifffile.tifffile import imwrite, imread

import matplotlib.pyplot as plt
from matplotlib.widgets  import RectangleSelector
import matplotlib.animation as animation


from skimage.util.dtype import img_as_float
import plotly.express as px

from dash import dcc # was import dash_core_components as dcc #!pip install dash-core-components
from dash import html # was import dash_html_components as html #!pip install dash-html-components
from dash.dependencies import Input, Output

from jupyter_dash import JupyterDash
import time

import cv2

try:
    cv2.setNumThreads(0)
except:
    pass


match virtenv:

    case 'caiman':

        if IN_COLAB:

            !rm -r '/content/CaImAn'
            !git clone https://github.com/flatironinstitute/CaImAn.git
            %cd '/content/CaImAn/'
            !pip install -e .

            #all below was in below caiman requirements.txt but bokeh needs older version
            #!pip install -r requirements.txt &> /dev/null

            !pip install bokeh == 2.4.3
            !pip install coverage
            !pip install cython
            !pip install h5py
            !pip install holoviews
            !pip install ipykernel
            !pip install ipython
            !pip install ipyparallel
            !pip install jupyter
            !pip install keras
            !pip install matplotlib
            !pip install mypy
            !pip install numpy
            !pip install numpydoc
            !pip install opencv-python
            !pip install peakutils
            !pip install pims
            !pip install psutil
            !pip install pynwb
            !pip install pyqtgraph
            !pip install scikit-image
            !pip install scikit-learn
            !pip install scipy
            !pip install tensorflow
            !pip install tifffile
            !pip install tk
            !pip install tqdm
            !pip install yapf

        import bokeh.plotting as bpl

        # #IMPORTANT! Newer versions of h5py will cause errors when saving results
        # !pip install h5py==2.10.0
        import h5py

        #IMPORTANT! Newer versions of ipyparallel will cause errors when saving starting a cluster
        #!pip install ipyparallel==8.1.0
        import ipyparallel

        if IN_COLAB: #can this be moved above?
            !python setup.py build_ext -i

        import caiman as cm
        import caiman.source_extraction.cnmf as cnmf
        from caiman.utils.visualization import nb_view_patches3d, plot_contours, nb_view_patches, nb_plot_contour


        ipyparalell?

        try:
            if __IPYTHON__:
                # this is used for debugging purposes only. allows to reload classes when changed
                get_ipython().magic('load_ext autoreload')
                get_ipython().magic('autoreload 2')
        except NameError:
            pass


        bpl.output_notebook()


        logging.basicConfig(format=
                                "%(relativeCreated)12d [%(filename)s:%(funcName)20s():%(lineno)s] [%(process)d] %(message)s",
                            # filename="/tmp/caiman.log",
                            #level=logging.INFO,
                            )


    case 'deepcad':

        import torch

        if torch.cuda.is_available():
            print('\033[1;31mGPU accessiable. Use GPU for computation.\033[0m')
            gpu_id = torch.cuda.current_device()
            total_memory = torch.cuda.get_device_properties(gpu_id).total_memory/1024/1024
            alloc_memory = torch.cuda.memory_allocated(0)/1024/1024
            print('GPU ID: ', gpu_id, '|', torch.cuda.get_device_name(), \
                '| Memory: {:.0f} MB'.format(total_memory))
            #nvcc--version
            print('PyTorch version: ', torch.__version__)
        else:
            print('\033[1;31mNo GPU support. Please enable GPUs for the notebook:\033[0m')
            print(' 1. Navigate to Edit → Notebook Settings')
            print(' 2. Select GPU from the Hardware Accelerator drop-down')

        if IN_COLAB:
            !pip install deepcad

        from deepcad.train_collection import training_class
        from deepcad.test_collection import testing_class
        from deepcad.movie_display import display, display_img
        from deepcad.utils import get_first_filename, download_demo

        if IN_COLAB: #can this be moved above?
            !pip install --upgrade onnx

        import yaml

        from csbdeep.utils import normalize #this won't work unless above is already installed??




In [ ]:
#@title map2opt


class map2opt():
    def __init__(self):

        self.params = {}
        self.params['m2p_merge_thresh'] = [.9]
        self.params['m2p_gsig'] = [2] #[2, 3, 4]
        self.params['m2p_nb'] = [1]
        self.params['SC_sigma'] = [1]
        self.params['lambda_gnmf'] = [1]
        self.params['perc_baseline_snmf'] = [20] #10, 20, 40]
        self.params['max_iter_snmf'] = [1000]

        self.map = []
        self.max_index = 1
        for key,val in self.params.items():
            self.outer(val)
            self.max_index *= len(val)
        self.max_index-= 1
        self.order = list(self.params.keys())

    def outer(self,l2):
        if self.map == []:
            self.map = [[f2] for f2 in l2]
        else:
            prod = []
            for f1 in self.map:
                for f2 in l2:
                    prod.append(f1+[f2])
            self.map = prod
        return None

    def map_index(self,index):
        assert 0 <= index <= self.max_index
        return self.map[index]



class map2opt_t5():
    def __init__(self):

        self.params = {}
        self.params['m2p_merge_thresh'] = [.9]
        self.params['m2p_gsig'] = [1, 2, 3] #[2, 3, 4]
        self.params['m2p_nb'] = [1, 2, 3]
        self.params['SC_sigma'] = [1, 4]
        self.params['lambda_gnmf'] = [1, 4]
        self.params['perc_baseline_snmf'] = [20,40] #10, 20, 40]
        self.params['max_iter_snmf'] = [1000]

        self.map = []
        self.max_index = 1
        for key,val in self.params.items():
            self.outer(val)
            self.max_index *= len(val)
        self.max_index-= 1
        self.order = list(self.params.keys())

    def outer(self,l2):
        if self.map == []:
            self.map = [[f2] for f2 in l2]
        else:
            prod = []
            for f1 in self.map:
                for f2 in l2:
                    prod.append(f1+[f2])
            self.map = prod
        return None

    def map_index(self,index):
        assert 0 <= index <= self.max_index
        return self.map[index]



In [ ]:
#@title configs


def configs(optex_setind = 'default', fnames = None, min_mov = 0,
            md = None, extract_in_2d = None, dims_spatial_ex = 0):

    #md['dims'] is dims of original fov, dims_spatial_ex is dims of extraction fov (which may be cropped, so not necessarily the same as md['dims']

    #motion correction configs

    pw_rigid = False
    nonneg_movie = True
    min_mov = min_mov
    shifts_opencv = True #true uses intercubic interp, false uses fourier, but i think something else overrides this setting elsewhere
    upsample_factor_grid = 4 #default 4
    niter_rig = 1 #default 1
    max_deviation_rigid = 3

    if md['dims'][1]==1:
        is3D_mc = False
        indices_mc = (slice(None), slice(None)) #if is3d is true for motion correction, will overwrite with nones and will lose indices_ex
        strides_mc = (24, 24)
        overlaps_mc = (12, 12)
        max_shifts_mc = (8, 8)
    else:
        is3D_mc = True
        indices_mc = (slice(None), slice(None), slice(None)) #if is3d is true for motion correction, will overwrite with nones and will lose indices_ex
        strides_mc = (24, 24, 6)
        overlaps_mc = (12, 12, 3)
        max_shifts_mc = (8, 8, 2)

    do_slices = False #my stackcrop is meant to replace this, so should always be false
    if do_slices:
        sly = slice(6, 51, 1)
        slx = slice(40, 181, 1)
        slz = slice(1, 9, 1)
        indices_ex = [slx, sly, slz]
    else:
        indices_ex = [slice(None), slice(None), slice(None)]


    only_init = False #only use the initialization run for extraction

    p = 0                   # order of the autoregressive system - 0 for nonspiking, 1 for instanteous rise but not decay, 2 for non-ionstantaneous rise and decay
    merge_thresh = 0.9
    gSig = [2, 2, 1] #forces to be odd so gsiz min is 3 (ie gsig 0.5 is same as 1)  # gSig = [3,3]            # radius (half-size) of average neurons (in pixels)
    nb = 1 #num background components

    fr = md['volrate'] #0.6193  #9.8465 frame period so 1000 / (9.8465 *(113+51)) # approximate frame rate of data - CONFIRMED FPS
    decay_time = .4         # length of transient - CONFIRMED APPROPRIATE FOR OUR INDICATOR GCaMP6f
    dxy = [md['xpix']/md['xfov'], md['ypix']/md['yfov'], md['numslice']/md['zfov']] #pixels per micron

    tsub = 1                # temporal downsampling
    ssub = 1               # spatial downsampling
    p_ssub = 1 #patch downsampling in space
    p_tsub = 1 #patch downsampling in time

    thr_method = 'nrg' #or 'max'
    maxthr = 0.1 #for  thr_method = 'max' keep pixels above this threshold
    nrgthr = 0.9999 #for  thr_method = 'nrg' keep pixels whose sorted cumsum contributes this much of total energy
    extract_cc = True #true will throw away isolated pixels of some kind

    method_init = 'graph_nmf' #'greedy_roi' #'graph_nmf' #sparse_NMF apparently has problems?? 'greedy_roi' python Caiman defaults to greedy_roi, looks for globular sources

    max_iter_snmf = 1000
    perc_baseline_snmf = 20
    alpha_snmf = 100 #default 1000 #for method_init sparseNMF
    #sigma_smooth_snmf = gSig #(2, 2, 0.5) #default 0.5 0.5 0.5

    lambda_gnmf = 1 #for method_init graphNMF
    SC_kernel = 'heat' #NOT TUNABLE NOW       # kernel for graph affinity matrix
    SC_sigma = 1              # std for SC kernel
    SC_thr = 0                 # threshold for affinity matrix
    SC_normalize = True        # standardize entries prior to computing affinity matrix
    SC_use_NN = False          # sparsify affinity matrix by using only nearest neighbors
    SC_nnn = 20                # number of nearest neighbors to use if SC_use_NN = True

    low_rank_background = True #True #true makes bankground nb, false makes it update with hals
    update_background_components = True

    fudge_factor = 0.96        # (default is 0.96; old value = 1) -- bias correction factor for discrete time constants
    ITER = 10                # (default is 2; old value=5) -- block coordinate descent iterations
    bas_nonneg = True #appears to not matter unless you're deconvolving (p is 1 or 2, not 0)

    rolling_sum = True #think (?) only relevant for init method greedy_roi

    #Each parameter has a low threshold (rval_lowest (default -1), SNR_lowest (default 0.5), cnn_lowest (default 0.1))
    # and high threshold (rval_thr (default 0.8), min_SNR (default 2.5), min_cnn_thr (default 0.9)).
    # A component has to exceed ALL low thresholds as well as ONE high threshold to be accepted.
    # can turn off CNN part withy use_CNN = false
    # these values will result in no roi filtering
    SNR_lowest = 0#0.5#0  #0.5 default       # minimum SNR for accepted components
    min_SNR = 0#0  #2.5 default    # accept components with that peak-SNR or higher
    rval_lowest = -1  # -1 default 0.6  # space correlation threshold
    rval_thr = 0#0  # 0.8 default  # space correlation threshold
    use_cnn = False      # True default # use the CNN classifier affects if 2 below params are used
    cnn_lowest = 0  #0.1 default  # neurons with cnn probability lower than this value are rejected
    min_cnn_thr = 0 #0.9 default # if cnn classifier predicts below this value, reject

    #stride_to_rf_ratio (along with gSig) is for automatic calculation of rf, stride, and k,
    # keep stride_to_rf_ratio in approxoimate range 0.3 - 0.8, give or take (don't stay >0 and <=1)
    # smaller stride_to_rf_ratio means larger patch with smaller patch overlap (caiman mistakenly calls patch overlap "stride")
    # caiman says patch dia should be 3-4 times neuron dia and patch stride should be at least neuron dia
    # this calculation is just based on the largest dim of neuron, to be conservative
    # if gsig is very diofferent across dims you may consider a different automated calculation of rf and stride and k
    #, example: when stride_to_rf_ratio = 0.3, patch is ~7 times larger and stride is 50% larger
    # another exmaple: when stride_to_rf_ratio = 0.8, patch is ~3 times larger and stride is 50% larger
    # since, patch dia = ceil(neuron_dia/stride_to_rf_ratio)+1)*2 and patch stride = ceil(ceil(neuron_dia/stride_to_rf_ratio)+1)*stride_to_rf_ratio)+1
    stride_to_rf_ratio = 0.65 #0.65

    if optex_setind != 'default': #create param set whose index matches value in optex_setind
        if md['dims'][1]==1:
            print("USING ALTERNATE map2opt FOR CARLS OLD PROJECT")
            map_index_2_params = map2opt_t5()
        else:
            map_index_2_params = map2opt()

        print('indexing into param set')
        merge_thresh, m2p_gsig, nb, SC_sigma, lambda_gnmf, perc_baseline_snmf, max_iter_snmf = \
            map_index_2_params.map_index(int(optex_setind))
        gSig = [m2p_gsig, m2p_gsig, 1]  #gSiz (made from gsig) will be 2 for 0.5 or 1, so don't bother with 0.5, and forcing 3rd element (z) to be 1 because my z sections are about half the neuron diameter

    if np.all(np.array(dims_spatial_ex)<50): #dont bother with patches if FOV is small enough (but this should be adjusted for dirtier drivers)
        do_patches = False
    else:
        do_patches = True
    #do_patches = False
    #determine k in automated way based on gSig, roi_decimation_fac, and stride_to_rf_ratio, while also satisfying caiman patch size recommendations
    roi_decimation_fac = 0.3  #1 is space filling, caiman demo is effectively around .33
    if do_patches: # PROCESS IN PATCHES AND THEN COMBINE, patches are useful if activity stats vary over fov (e.g. extracting same neurons from regions with varying SNR, patch runs will adapt to local stats)

        if extract_in_2d==True:
            maxsig = np.max(gSig[0:2])
        else:
            maxsig = np.max(gSig)

        rf = int(np.ceil((maxsig*2+1) / stride_to_rf_ratio)) + 1
        stride_cnmf = int(np.ceil(rf * stride_to_rf_ratio)) + 1

        p_patch = p
        nb_patch = nb
        if extract_in_2d==True:
            k = int(np.round( (rf*2*rf*2) / ((gSig[0]*2+1)*(gSig[1]*2+1))*roi_decimation_fac))  # number of components in each patch, rf and gsig are both half sizes
        else:
            if rf*2<dims_spatial_ex[2]:
                rfz = rf*2
            else:
                rfz = dims_spatial_ex[2]
            k = int(np.round( (rf*2*rf*2*rfz) / ((gSig[0]*2+1)*(gSig[1]*2+1)*(gSig[2]*2+1))*roi_decimation_fac))  # number of components in each patch, rf and gsig are both half sizes
        indices_ex = [slice(None), slice(None), slice(None)]
    else:                   # PROCESS THE WHOLE FOV AT ONCE
        rf = None # will run CNMF on the whole FOV
        stride_cnmf = None       # will run CNMF on the whole FOV
        p_patch = p
        nb_patch = nb
        k = int(np.round( np.prod(dims_spatial_ex) / ((gSig[0]*2+1)*(gSig[1]*2+1)*(gSig[2]*2+1))*roi_decimation_fac))  # number of components in each patch, rf and gsig are both half sizes

    dimstr = "3dex"
    if extract_in_2d==True:
        dimstr = '2dex'
        indices_ex = indices_ex[:-1] #change from 3d to 2d
        dxy = dxy[:-1] #change from 3d to 2d
        gSig = gSig[:-1] #change from 3d to 2d

    gSiz = [int(np.round(2*gstmp + 1)) for gstmp in gSig] #put here at end to register any gSig change
    se = np.ones((3,)*len(gSig), dtype=np.uint8)  #put here at end to register any gSig change #se = np.ones((3,3,1), dtype=np.uint8)
    #medw = (3,)*len(gSig)

    sigma_smooth_snmf = [0.5] #append this filter sigma for time to beginning (when it is applied time is in 1st dim?)
    sigma_smooth_snmf.extend(gSig)
    if extract_in_2d==False:
        sigma_smooth_snmf[-1] = 0.5 #sigma_smooth_snmf can actually use values<1, if 3d extraction, make small for coarse z samples


    fnadd = str(gSig[0]) + '_' + str(nb) + '_' + str(merge_thresh) \
        + '_' + str(rf) + '_' + str(SC_sigma) + '_' + str(lambda_gnmf) + '_' + str(perc_baseline_snmf) \
        + '_' + str(max_iter_snmf) + '_' + str(ITER) \
        + '_' + str(k) + '_' + method_init.split('_')[0] + '_' + dimstr

    if extract_in_2d is None: #it's none during motion correction, when we don't care about these params, rather than true/false
        print("motion correction params configured")
    else:
        print("optex_setind is " + str(optex_setind) + " with filename string " + fnadd)

    opts_dict = {'strides': strides_mc,    # start a new patch for pw-rigid motion correction every x pixels
                'overlaps': overlaps_mc,   # overlap between pathes (size of patch strides+overlaps)
                'max_shifts': max_shifts_mc,   # maximum allowed rigid shifts (in pixels)
                'max_deviation_rigid': max_deviation_rigid,  # maximum shifts deviation allowed for patch with respect to rigid shifts
                'pw_rigid': pw_rigid,         # flag for performing non-rigid motion correction
                'is3D': is3D_mc,
                'nonneg_movie':nonneg_movie,
                'min_mov': min_mov,
                'shifts_opencv':shifts_opencv,
                'niter_rig':niter_rig,
                'upsample_factor_grid':upsample_factor_grid,
                'fr': fr,
                'p': p,
                'nb': nb,
                'merge_thr': merge_thresh,
                'rf': rf,
                'indices': indices_mc,  #for some reason indices_mc is causing error, maybe needs list for mc and tuple for extraction?
                'K': k,
                'gSig': gSig,
                'gSiz': gSiz,
                'stride': stride_cnmf,
                'method_init': method_init,
                'sigma_smooth_snmf': sigma_smooth_snmf,
                'perc_baseline_snmf': perc_baseline_snmf,
                'max_iter_snmf': max_iter_snmf,
                'sigma_smooth_snmf': sigma_smooth_snmf,
                'SC_kernel': SC_kernel, #NOT TUNABLE NOW       # kernel for graph affinity matrix
                'SC_sigma': SC_sigma,            # std for SC kernel
                'SC_thr': SC_thr,                 # threshold for affinity matrix
                'SC_normalize': SC_normalize,        # standardize entries prior to computing affinity matrix
                'SC_use_NN': SC_use_NN,          # sparsify affinity matrix by using only nearest neighbors
                'SC_nnn': SC_nnn,                # number of nearest neighbors to use if SC_use_NN = True
                'lambda_gnmf': lambda_gnmf, #for method_init graphNMF
                'alpha_snmf': alpha_snmf, #for method_init sparseNMF
                #'dims': dims,
                'dxy': dxy,
                'decay_time': decay_time,
                'bas_nonneg': bas_nonneg,
                'p_patch': p_patch,
                'nb_patch': nb_patch,
                'se': se,
                'rolling_sum': rolling_sum,
                'only_init': only_init,
                'ssub': ssub,
                'tsub': tsub,
                'p_ssub': p_ssub,
                'p_tsub': p_tsub,
                'SNR_lowest': SNR_lowest,
                'min_SNR': min_SNR,
                'rval_thr': rval_thr,
                'rval_lowest': rval_lowest,
                'use_cnn': use_cnn,
                'min_cnn_thr': min_cnn_thr,
                'cnn_lowest': cnn_lowest,
                'ITER': ITER,
                'fudge_factor': fudge_factor,
                'cnn_lowest': cnn_lowest,
                'update_background_components': update_background_components,
                'low_rank_background' : low_rank_background,
                'thr_method': thr_method,
                'maxthr': maxthr,
                'nrgthr': nrgthr,
                'fnames': fnames,
                #'medw': medw,
                'extract_cc': extract_cc}


    # # for reference here are the initialization defs for 3 methods, sparse_nmf apparently "has problems" according to gitter

    # # greedyROI(Y, nr=30, gSig=[5, 5], gSiz=[11, 11], nIter=5, kernel=None, nb=1,
    #           rolling_sum=False, rolling_length=100, seed_method='auto')

    # for graphnmf all these are tunable in cnmf params except remove_baseline, truncate, tol, and SC_kernel whose defaults are below
    # note SC_kernel appears to be tunable because it's in params but it is not, heat is default
    # # graphNMF(Y_ds, nr, max_iter_snmf=500, lambda_gnmf=1,
    #          sigma_smooth=(.5, .5, .5), remove_baseline=True,
    #          perc_baseline=20, nb=1, truncate=2, tol=1e-3, SC_kernel='heat',
    #          SC_normalize=True, SC_thr=0, SC_sigma=1, SC_use_NN=False,
    #          SC_nnn=20

    # for sparsenmf all these are tunable in cnmf params except remove_baseline and truncate, whose defaults are below
    # # sparseNMF(Y_ds, nr, max_iter_snmf=500, alpha=10e2, sigma_smooth=(.5, .5, .5),
    #           remove_baseline=True, perc_baseline=20, nb=1, truncate=2)


    return opts_dict, indices_ex, fnadd




In [ ]:
#@title read and save metadata


def mdsisv(pth_readfile, pthmd, pthmd_npy, mat_file_shape = None):

    mdt = {}

    if mat_file_shape is None:

        # use ScanImageTiffReader to read metadata (strange ping because scanimage tif headers are not saved as json)
        meta = ScanImageTiffReader(pth_readfile).metadata()
        mdt['numvol'] = int(re.findall( 'actualNumVolumes = (.*)', meta)[0])
        mdt['numslice_withflyback'] = int(re.findall( 'numFramesPerVolumeWithFlyback = (.*)', meta)[0])
        mdt['numslice'] = int(re.findall( 'actualNumSlices = (.*)', meta)[0])
        mdt['xpix'] = int(re.findall( 'pixelsPerLine = (.*)', meta)[0])
        mdt['ypix'] = int(re.findall( 'linesPerFrame = (.*)', meta)[0])
        mdt['flyback'] = mdt['numslice_withflyback'] - mdt['numslice']
        mdt['dims'] = [mdt['numvol'], mdt['numslice_withflyback'] - mdt['flyback'], mdt['ypix'], mdt['xpix']]
        fovtmp = literal_eval(re.findall( 'imagingFovUm = (.*)', meta)[0].replace(" ",",").replace(";",","))
        mdt['xfov'] = abs(fovtmp[0]) + abs(fovtmp[2])
        mdt['yfov'] = abs(fovtmp[1]) + abs(fovtmp[3])
        mdt['zwid'] = int(re.findall( 'actualStackZStepSize = (.*)', meta)[0])
        mdt['zstartpos'] = literal_eval(re.findall( 'zsRelative = (.*)', meta)[0].replace(";",","))
        mdt['zfov'] = mdt['zstartpos'][-1] + mdt['zwid'] - mdt['zstartpos'][0]
        mdt['framerate'] = float(re.findall( 'scanFrameRate = (.*)', meta)[0])
        mdt['volrate'] = float(re.findall( 'scanVolumeRate = (.*)', meta)[0])

    else:

        mdt['dims'] = [mat_file_shape[0], 1, mat_file_shape[1], mat_file_shape[2]] #z size (2nd dim) is 1 because old project is not volumetric
        mdt['framerate'] = 20
        mdt['volrate'] = 20
        mdt['xpix'] = 256
        mdt['xfov'] = 74
        mdt['ypix'] = 128
        mdt['yfov'] = 37
        mdt['numslice'] = 1
        mdt['numslice_withflyback'] = 1
        mdt['numvol'] = mat_file_shape[0]
        mdt['zfov'] = 1  #set to 1 to avoid division by zero later, even though it's not really 1
        mdt['flyback'] = 0
        mdt['zwid'] = 0
        mdt['zstartpos'] = 0


    md = fromarrays( [ mdt['numvol'], mdt['numslice_withflyback'], mdt['numslice'], mdt['xpix'], \
        mdt['ypix'], mdt['flyback'], mdt['xfov'], mdt['yfov'], \
        mdt['zwid'], mdt['zfov'], mdt['framerate'], mdt['volrate'] ], \
        names = ['numvol', 'numslice_withflyback', 'numslice', 'xpix', 'ypix', 'flyback', \
            'xfov', 'yfov', 'zwid', 'zfov', 'framerate', 'volrate' ] )

    sio.savemat(pthmd, {'md': md}) #save for matlab part of pipeline

    with open(pthmd_npy, 'wb') as fnmd: #and save as npy file for rest of python pipeline
        np.save(fnmd, mdt)

    return mdt


In [ ]:
#@title cropping functions

def select_fov_z(images):

  %matplotlib inline

  numim = images.shape[-1]

  Nc = 3
  Nr = int(np.ceil(numim/Nc))
  fig, ax = plt.subplots(Nr, Nc)
  for i in range(numim):
      indies = np.unravel_index(i, (Nr,Nc))
      ax[indies[0],indies[1]].imshow(images[:,:,i].T)
      ax[indies[0],indies[1]].axis('off')
  interval = 5 # units of seconds
  plt.pause(interval)
  plt.show()
  print("what z slices do you want to keep? consider keeping first as padding if cells abut z edges")
  zlimits = literal_eval(input ("choose z limits, format (firstframe,lastframe) one-indexed: "))
  return zlimits



def draw_rect_xy(img, fn_crop_lim_xy):

  img = img.T
  fig = px.imshow(img)
  fig_hist = px.histogram(img.ravel())

  fig.update_layout(
      autosize=False,
      # width=500,
      height=400,
      dragmode='drawrect',
      newshape=dict(line_color='cyan', line_width=0.5))

  # this doesn't work: plots a second figure that is editable but lacks propertiers of the other
  # fig.show(config={
  #           'editable': True,
  #           'edits': {'shapePosition': True}})

  app = JupyterDash(__name__)
  app.layout = html.Div(
      [
          html.H3("Drag a rectangle to show the histogram of the ROI"),
          html.Div([dcc.Graph(id="middle-sai", figure=fig)], style={"width": "60%", "display": "inline-block", "padding": "0 0"}),
          html.Pre(id="bbox-data", style={"width": "10%", "display": "inline-block", "padding": "0 0"}),
          #html.Div(id='all-bboxes',style={"color": "white"}),
          html.Div([dcc.Graph(id="histogram", figure=fig_hist)], style={"width": "30%", "display": "inline-block", "padding": "0 0"}),
      ]
  )

  @app.callback(
      Output("histogram", "figure"),
      Output("bbox-data", "children"),
      Input("middle-sai", "relayoutData"),
      prevent_initial_call=True,
  )
  def on_new_annotation(relayout_data):

      if "shapes" in relayout_data:

          last_shape = relayout_data["shapes"][-1]
          x1tmp, y0tmp = int(last_shape["x0"]), int(last_shape["y0"]) #slicing requires ints
          x0tmp, y1tmp = int(last_shape["x1"]), int(last_shape["y1"]) #slicing requires ints
          #so the coords don't depend on where you clicked first/last
          x0 = min(x0tmp,x1tmp)
          x1 = max(x0tmp,x1tmp)
          y0 = min(y0tmp,y1tmp)
          y1 = max(y0tmp,y1tmp)
          roi_img = img[y0:y1, x0:x1]
          coords = (y0, y1, x0, x1)
          croplimxy = np.asarray(coords).astype(int)
          with open(fn_crop_lim_xy, 'wb') as fncrop:
              np.save(fncrop, croplimxy)
          return px.histogram(roi_img.ravel()),  html.Div(str(coords), style={"color": "white"})

      else:
          return no_update


  #del app.config._read_only["requests_pathname_prefix"]
  app.run()
  #app.run_server(mode='inline', host='localhost', port=1050)
  #app.run_server(mode='external')


In [ ]:
#@title bgremover


class bgremover:

    def __init__(self, img, pth_save_prefix, half_wid=12, dimorder='tyx'):
        self.half_wid = half_wid
        self.pth_save_prefix = pth_save_prefix
        if dimorder=='tyx':
            self.img = img
        elif dimorder=='txy':
            self.img = np.transpose(img, (0, 2, 1))

    def draw_patches(self):
        half_wid = self.half_wid
        wid = 2*half_wid
        kernel = np.ones(wid)/wid
        self.meanframe = np.mean(self.img, axis=0)
        bg_ind = []
        for line in self.meanframe:
            tmp = np.convolve(line, kernel, 'valid')
            bg_center = np.argmin(tmp) + half_wid
            bg_ind.append([bg_center-half_wid, bg_center+half_wid])
        self.bg_ind = bg_ind

    def remove_bg(self, offset=0):
        bg_ind = self.bg_ind
        out = self.img.copy()
        for ind in range(out.shape[1]):
            patch = self.img[:, ind, :]
            bg_patch = self.img[:, ind, bg_ind[ind][0]:bg_ind[ind][1]]
            bg = bg_patch.mean(axis=-1)
            patch = patch-bg[None].T
            out[:, ind, :] = patch
        out = out + offset # compensate so that most of the pixels are above 0 (deprecated)
        self.out = out

    def make_plots(self):

        half_wid = self.half_wid

        patch_im = np.mean(self.img, axis=0)
        mv = np.max(patch_im)
        for i in range(patch_im.shape[0]):
            patch_im[i, self.bg_ind[i][0]:self.bg_ind[i][1]] = mv

        y_len, x_len = self.out.shape[1:3]
        test_y = random.randint(0, y_len-1)
        test_x = random.randint(0, x_len-2*half_wid-1) + half_wid

        test_patch = self.img[:, test_y, test_x-half_wid:test_x+half_wid]
        test = test_patch.mean(-1)
        test = test/test.mean()

        fs = self.img.shape[-1]
        f, Pxx_den = signal.periodogram(test, fs)
        fig, ((ax1, ax2), (ax3, ax4), (ax5, ax6), (ax7, ax8)) = plt.subplots(4, 2)
        ax1.semilogy(f[1:], Pxx_den[1:]) #skip 0 frequency

        test_patch = self.out[:, test_y, test_x-half_wid:test_x+half_wid]
        test = test_patch.mean(-1)
        test = test/test.mean()

        f, Pxx_den = signal.periodogram(test, fs)
        ax2.semilogy(f[1:], Pxx_den[1:]) #skip 0 frequency

        ax3.imshow(self.meanframe)
        ax3.axis('off')

        self.meanframe_nobg = np.mean(self.out, axis=0)

        ax4.imshow(self.meanframe_nobg)
        ax4.axis('off')

        ax5.hist(self.img.ravel(), bins=50)
        ax5.set_yscale('log')
        ax6.hist(self.out.ravel(), bins=50)
        ax6.set_yscale('log')

        ax7.imshow(patch_im)

        plt.savefig(self.pth_save_prefix + '_bgplots.png')
        plt.close()




In [ ]:
#@title denoised plotting function

def plot_denoised_movie(filename = None, pthsave = None, filename_add = 'add', cropflag = 0, display_length = 20, norm_min_percent = 0, norm_max_percent = 100):

  %matplotlib inline

  print(filename)
  sliceind = int(filename.split('/')[-1].split('_')[3])

  fn_savegif = pthsave + '/' + filename.split('/')[-1] + '_' + filename_add + '_.mp4'
#  fn_savegif = filename[:-4] + '_' + filename_add + '_.mp4'
  Ynew = imread(filename).astype(denoise_dtype)
  print(Ynew.shape)

  #img = normalize(Ynew, norm_min_percent, norm_max_percent)


  fig, ax = plt.subplots()
  ims = []
  if cropflag:
    fuk = range(49,350)
  else:
    fuk = range(Ynew.shape[0])

  for i in fuk:
    im = ax.imshow(Ynew[i,:,:], animated=True)
    if i == 0:
        ax.imshow(Ynew[i,:,:]) # show an initial one first
    ims.append([im])

  ani = animation.ArtistAnimation(fig, ims, interval=200, repeat=True, blit=True, repeat_delay=1000) #originally repeat false
  ani.save(fn_savegif)
  # writer = animation.FFMpegWriter(fps=15, metadata=dict(artist='Me'), bitrate=1800)
  # ani.save(fn_savegif, writer=writer)

  #plt.show()

In [ ]:
#@title separate_z_slices_before_denoising (old project)

def separate_z_slices_before_denoising_carls_old_project(pth_input, fn_prefix, pth_denoising, dims, denoise_volume):

    Y = imread(pth_input)
    Y = Y.reshape(dims)
    Y = np.transpose(Y, (0, 2, 3, 1)) #put in order t y x z (not t x y z)
    if Y.dtype!='uint16':
        raise Exception("dtype should be uint16 (arbitrary choice for this pipeline)")
    zind_all_dn = np.arange(dims[1])

    for zii in zind_all_dn: #deepcad wants 3d data, so organize slices into separate tif files, and put in one folder (if denoise_volume=1, ie train on all slices) or separate folders (if denoise_volume=0, ie train on z subset)

        Ynew = Y[:,:,:,zii]
        Lt, Ly, Lx = Ynew.shape
        denoise_input_dtype = Ynew.dtype
        if Ynew.shape != (dims[0], dims[2], dims[3]):
            raise Exception("dims changed")

        if denoise_volume:
            pretend_z = str(int(fn_prefix.split('_')[2]) - 1) #make it zero indexed
            pretend_trial = '1' # pretend they all come from same trial
            dnfolder = fn_prefix.split('_')[0] + '_' + fn_prefix.split('_')[1] + '_' + pretend_trial + '_all' #for these non-volumetric grad recordings, if do_volume == 1, rename all trials "1", and each trial a different z slice
            tifname = fn_prefix.split('_')[0] + '_' + fn_prefix.split('_')[1] + '_' + pretend_trial + '_' + pretend_z + '_' + str(Lt) + '_' + str(Ly)  + '_' + str(Lx) + '_' + str(denoise_input_dtype) + '_.tif'
        else: #if not denoise_volume, just keep it the way it is (all trials have only z slice 0)
            actual_z = '0' #make it zero indexed
            dnfolder = fn_prefix + '_' + actual_z
            tifname = fn_prefix + '_' + actual_z + str(Lt) + '_' + str(Ly)  + '_' + str(Lx) + '_' + str(denoise_input_dtype) + '_.tif'

        print(tifname)
        pth_trainset = pth_denoising + '/' + dnfolder #dir containing all tif files for training
        pth_tif_pdn = pth_trainset + '/' + tifname

        # for old project cannot remove folder because it saves from separate runs of register
        # if os.path.exists(pth_trainset) and (zii==0 or denoise_volume==0): #if you're on the first zii (regardless of denoise_volume value), or for all zii if denoise_volume==0
        #     shutil.rmtree(pth_trainset) #REMOVE any existing training folder before training, to ensure models don't get mixed (until "resume training" functionality is written)

        if not os.path.exists(pth_trainset): #don't make this "else" connected to "if" above because you have to evaluate it
            os.mkdir(pth_trainset)
        imwrite(pth_tif_pdn, Ynew, photometric = 'minisblack' ) #put the tif in the folder deepcad looks to for training data


In [ ]:
#@title separate_z_slices_before_denoising

def separate_z_slices_before_denoising(pth_input, fn_prefix, pth_denoising, dims, denoise_volume):

    Y = imread(pth_input)
    Y = Y.reshape(dims)
    Y = np.transpose(Y, (0, 2, 3, 1)) #put in order t y x z (not t x y z)
    if Y.dtype!='uint16':
        raise Exception("dtype should be uint16 (arbitrary choice for this pipeline)")
    zind_all_dn = np.arange(dims[1])

    for zii in zind_all_dn: #deepcad wants 3d data, so organize slices into separate tif files, and put in one folder (if denoise_volume=1, ie train on all slices) or separate folders (if denoise_volume=0, ie train on z subset)

        Ynew = Y[:,:,:,zii]
        Lt, Ly, Lx = Ynew.shape
        denoise_input_dtype = Ynew.dtype
        if Ynew.shape != (dims[0], dims[2], dims[3]):
            raise Exception("dims changed")

        if denoise_volume:
            dnfolder = fn_prefix + '_all'
        else:
            dnfolder = fn_prefix + '_' + str(zii)
        tifname = fn_prefix + '_' + str(zii) + '_' + str(Lt) + '_' + str(Ly)  + '_' + str(Lx) + '_' + str(denoise_input_dtype) + '_.tif'

        print(tifname)
        pth_trainset = pth_denoising + '/' + dnfolder #dir containing all tif files for training
        pth_tif_pdn = pth_trainset + '/' + tifname

        if os.path.exists(pth_trainset) and (zii==0 or denoise_volume==0): #if you're on the first zii (regardless of denoise_volume value), or for all zii if denoise_volume==0
            shutil.rmtree(pth_trainset) #REMOVE any existing training folder before training, to ensure models don't get mixed (until "resume training" functionality is written)

        if not os.path.exists(pth_trainset): #don't make this "else" connected to "if" above because you have to evaluate it
            os.mkdir(pth_trainset)
        imwrite(pth_tif_pdn, Ynew, photometric = 'minisblack' ) #put the tif in the folder deepcad looks to for training data


In [ ]:
#@title stitchdn (old project)

def stitchdn_carls_old_project(pth_denoising, fn_prefix, pth_out, dims_pre_denoise, denoise_volume, epoch_choose):

  goal_trial = int(fn_prefix.split('_')[2])
  actual_z_size = 1

  if denoise_volume == 1:
    pretend_trial = '1' # pretend they all come from same trial
    dnfolder = fn_prefix.split('_')[0] + '_' + fn_prefix.split('_')[1] + '_' + pretend_trial + '_all/' #for these non-volumetric grad recordings, if do_volume == 1, rename all trials "1", and each trial a different z slice
    pth_trainset_all = natsorted(glob.glob(pth_denoising + '/' + dnfolder))

  else:

    pth_trainset_all = natsorted(glob.glob(os.path.join(pth_denoising, fn_prefix + '_*/')))
    fldr_exclude = fn_prefix.split('_')[0] + '_' + fn_prefix.split('_')[1] + '_' + pretend_trial + '_al*/'
    pth_trainset_all = list(set(pth_trainset_all) - set(natsorted(glob.glob(fldr_exclude)))) #exclude the "all" folders when denoise_volume==1

  countz = 0
  for pth_trainset in pth_trainset_all:


    fldr_chex = natsorted(glob.glob(os.path.join(pth_trainset, 'DataFolderIs_*')))
    for fcxi,fcx in enumerate(fldr_chex):
      if fcxi!=len(fldr_chex)-1:
          print("deleting this denoise test folder from old run")
          print(fcx)
          shutil.rmtree(fcx)


    fldr_outtiff_all = natsorted(glob.glob(os.path.join(pth_trainset, 'DataFolderIs_*', 'E_*'))) #for all epochs that were used for denoising, organize tif files into single folder in 'denoised' folder
    for fldr_outtiff in fldr_outtiff_all:
      if fnmatch.fnmatch(fldr_outtiff.split('/')[-1], 'E_' + "{:02d}".format(epoch_choose) + '_Iter_*'):
        pth_denoised_singles = natsorted(glob.glob(os.path.join(fldr_outtiff, '*output.tif')))

        Y = np.zeros((dims_pre_denoise[0], dims_pre_denoise[2], dims_pre_denoise[3], actual_z_size)) #t y x z
        print(dims_pre_denoise[1])
        for fni,f in enumerate(pth_denoised_singles): #loop over each denoised z slice and reassemble into array matching shape of original 4d volume
            if denoise_volume == 1:
                trial = int(f.split('/')[-1].split('_')[3]) + 1 #filename z position is actual trial if denoise_volume was==1, add one bc they were made zero index, but original trial is one indexed
            else:
                trial = int(f.split('/')[-1].split('_')[2]) #filename trial is in nortmal trial position

            if trial == goal_trial:
                countz = countz + 1
                print(f)
                sliceind = 0 #always zero for these non-volumetric old recordings
                Ynew = imread(f)
                if Ynew.dtype!='uint16':
                    print("warning, converting type from " + str(Ynew.dtype))
                    Ynew = Ynew.astype('uint16')
                    if np.min(Y)<0 or np.max(Y) > 65535:
                      raise Exception("denoising have operated on uint16 for this pipeline, or adjust it")
                print(Ynew.dtype)
                print(sliceind)
                Y[:,:,:,sliceind] = Ynew

                mnmv = np.min(Y)
                Y = Y - mnmv #make nonnegative before writing to uint16
                print("MIN AFTER DENOISING " + str(mnmv))
                Y = Y.astype('uint16')
                Y = np.transpose(Y, (0, 3, 1, 2)) #tzyx
                print(Y.shape)
                Y = Y.reshape(dims_pre_denoise[0] * actual_z_size, dims_pre_denoise[2], dims_pre_denoise[3]) #(tz)yx
                print(Y.shape)
                imwrite(pth_out, Y.squeeze()) #write the registered movie as tif for use in matlab, and caiman extraction below


        if countz != dims_pre_denoise[1]:
            raise Exception("more or less than one slice present")


In [ ]:
#@title stitchdn

def stitchdn(pth_denoising, fn_prefix, pth_out, dims_pre_denoise, denoise_volume, epoch_choose):

  if denoise_volume == 1:
    pth_trainset_all = natsorted(glob.glob(os.path.join(pth_denoising, fn_prefix + '_all/')))
  else:
    pth_trainset_all = natsorted(glob.glob(os.path.join(pth_denoising, fn_prefix + '_*/')))
    pth_trainset_all = list(set(pth_trainset_all) - set(natsorted(glob.glob(os.path.join(pth_denoising, fn_prefix + '_al*/'))))) #exclude the "all" folders when denoise_volume==1

  Y = np.zeros((dims_pre_denoise[0], dims_pre_denoise[2], dims_pre_denoise[3], dims_pre_denoise[1])) #t y x z

  countz = 0
  for pth_trainset in pth_trainset_all:

    fldr_chex = natsorted(glob.glob(os.path.join(pth_trainset, 'DataFolderIs_*')))
    for fcxi,fcx in enumerate(fldr_chex):
      if fcxi!=len(fldr_chex)-1:
          print("deleting this denoise test folder from old run")
          print(fcx)
          shutil.rmtree(fcx)

    fldr_outtiff_all = natsorted(glob.glob(os.path.join(pth_trainset, 'DataFolderIs_*', 'E_*'))) #for all epochs that were used for denoising, organize tif files into single folder in 'denoised' folder
    for fldr_outtiff in fldr_outtiff_all:

      if fnmatch.fnmatch(fldr_outtiff.split('/')[-1], 'E_' + "{:02d}".format(epoch_choose) + '_Iter_*'):
        pth_denoised_singles = natsorted(glob.glob(os.path.join(fldr_outtiff, '*output.tif')))

        for fni,f in enumerate(pth_denoised_singles): #loop over each denoised z slice and reassemble into array matching shape of original 4d volume
            countz = countz + 1
            print(f)
            sliceind = int(f.split('/')[-1].split('_')[3])
            Ynew = imread(f)
            if Ynew.dtype!='uint16':
                print("warning, converting type from " + str(Ynew.dtype))
                Ynew = Ynew.astype('uint16')
                if np.min(Y)<0 or np.max(Y) > 65535:
                  raise Exception("denoising have operated on uint16 for this pipeline, or adjust it")
            print(Ynew.dtype)
            print(sliceind)
            Y[:,:,:,sliceind] = Ynew

  if countz != dims_pre_denoise[1]:
      raise Exception("not all slices present")

  mnmv = np.min(Y)
  Y = Y - mnmv #make nonnegative before writing to uint16
  print("MIN AFTER DENOISING " + str(mnmv))
  Y = Y.astype('uint16')
  Y = np.transpose(Y, (0, 3, 1, 2)) #tzyx
  print(Y.shape)
  Y = Y.reshape(dims_pre_denoise[0] * dims_pre_denoise[1], dims_pre_denoise[2], dims_pre_denoise[3]) #(tz)yx
  print(Y.shape)
  #imwrite(pth_out, Y.squeeze()) #squeeze was just for non-volumetric (old project), does it change header, slowing read dramatically?
  imwrite(pth_out, Y) #write the registered movie as tif for use in matlab, and caiman extraction below




In [ ]:
#@title choose files


def filefind(recdates, pth_allrec, fly, trial, jobind, do_background_subtraction,
                 use_background_subtracted, do_register):

    countz = -1 #so first one is zero, since jobind is zero indexed
    for recording_date in recdates:

        pth_fldrs_pattern = pth_allrec + recording_date + '-' + fly + '_*/'
        fn_pattern = recording_date + '-' + fly + '*_trial_00' + trial + '_*.tif'
        pth_fldrs = natsorted(glob.glob(pth_fldrs_pattern))
        old_mat_files = 0
        if not pth_fldrs:  #if no matches try another filename pattern (files from previous project)
            old_mat_files = 1
            pth_fldrs_pattern = pth_allrec + recording_date + '_' + fly + '_*/'
            fn_pattern = recording_date + '_' + fly + '_' + trial + '_stackraw_.mat'
            pth_fldrs = natsorted(glob.glob(pth_fldrs_pattern))

        for fldr in pth_fldrs:

            print(fldr)

            pth_allfiles = natsorted(os.listdir(fldr))

            for f in pth_allfiles:

                if fnmatch.fnmatch(f, fn_pattern):

                    countz = countz + 1

                    if jobind == 'all' or (jobind !='all' and countz==jobind): #if 'all', do all files matching pattern, otherwise only file matching index

                        pth_readfile = fldr + f
                        print(pth_readfile)

                        if old_mat_files:
                            fn_prefix = '_'.join(f.split('_')[:3])
                        else:
                            fn_prefix = f.split('_')[0].split('-')[0] + '_' + f.split('_')[0].split('-')[1]  + '_' + f.split('_')[-2][-1] #change hyphen to underscore

                        pth_prefix = fldr + fn_prefix
                        if do_background_subtraction or (use_background_subtracted and not do_register):
                            pth_tif_dn = pth_prefix + '_cmrg_bksb_dcdn_.tif'
                            pth_tif_reg_tmp = pth_prefix + '_cmrg_bksb_tmp_.tif'
                            pth_tif_reg = pth_prefix + '_cmrg_bksb_.tif'
                        else:
                            pth_tif_dn = pth_prefix + '_ord_.tif'
                            pth_tif_reg_tmp = pth_prefix + '_cmrg_tmp_.tif'
                            pth_tif_reg = pth_prefix + '_cmrg_.tif'

                        pthmd = pth_prefix + '_mdsi_.txt'
                        pthmd_npy = pthmd[:-4] + '.npy'

                        if old_mat_files: #for my old project

                            pth_readfile_new = pth_readfile[:-4] + '.tif'

                            if os.path.isfile(pthmd_npy) and os.path.isfile(pth_readfile_new): #
                                md = np.load(pthmd_npy, allow_pickle='TRUE').item() #if it exists, the md file will too
                                pth_readfile = pth_readfile_new
                            else:
                                mat = mat73.loadmat(pth_readfile)
                                Y = mat['stackRaw_pmc'] # Y = mat['stackRaw_mc']
                                mnmv = np.min(Y)
                                Y = Y - mnmv #make movie nonnegative (not sure this is necessary)
                                print("MIN OF STACKRAW_PMC MAT FILE " + str(mnmv))
                                Y = np.transpose(Y, (2, 0, 1)) #put in order t y x (not t x y) #stackraw_mc may be flipped relative to stackraw pmc
                                pth_readfile = pth_readfile_new
                                imwrite(pth_readfile, Y.astype('uint16')) #write as t x y z (singleton z at end)
                                md = mdsisv(pth_readfile, pthmd, pthmd_npy, mat_file_shape = Y.shape)

                        else:

                            fn_prefix = f.split('_')[0].split('-')[0] + '_' + f.split('_')[0].split('-')[1]  + '_' + f.split('_')[-2][-1] #change hyphen to underscore
                            if os.path.isfile(pthmd_npy):
                                md = np.load(pthmd_npy, allow_pickle='TRUE').item()
                            else:
                                md = mdsisv(pth_readfile, pthmd, pthmd_npy, mat_file_shape = None)


    return (pth_readfile, fn_prefix, pth_prefix, pth_tif_reg_tmp, pth_tif_reg, pth_tif_dn, md)


In [ ]:
#@title entrypoint


recdates = ['20230627'] #list of strings, as it appears in the directory and raw file filename (with hyphen not underscore for now), '*' for any
fly = '2' #string, fly optex_setind, '*' for any
trial = '2' #string, trial optex_setind, '*' for any
jobind = 'all' #if 'all', loop over all recordings matching pattern in pth_allrec, if not 'all', zero indexed (can be str or int) specifying to operate on recording whose index (in sorted list of all recordings in pth_allrec) matches value in jobind

do_register = 0 #caiman normCorre registration
do_background_subtraction = 0 #won't happen unless do_register = True
bg_patch_halfwidth = 3 #half width of patch over which mean is computed for background subtraction (patch is a line in x)

do_denoise = 0 #deepcad denoising(from the more recent deepcadrt, although this is not real time), input must be motion_corrected
denoise_volume = 1 #for denoise_volume = 1, denoise_slice_index must be 'all', and this will train on all z slices together . . . if denoise_volume = 0, denoise_slice_index must be 'all', or single index, and will trains on each z slice separately
denoise_slice_index = 'all' #either 'all' (all z slices) or a single number (a single z slice) . . . this is which z slices get denoised (not the same as which z slices are used to train model, although see above notes for denoise_volume)

do_extract = 1 #caiman source extraction
rgname = ['pb', 'gar', 'gal', 'no'] #list of strings specifying names for xy rectangular or xyz cuboid fov subregions that are passed separately to source extraction; interactive plots prompt user to define z range and draw xy rectangle; use ['fullfov'] to extract from entire FOV
extract_in_2d = 0 #caiman source extraction for each plane independently (WARNING, 3D EXTRACTION REQUIRES AT LEAST 3 ELEMENTS IN EACH DIMENSION X Y and Z, OR you must REWRITE binary_closing IN CAIMAN'S THRESHOLD_COMPONENTS)
use_background_subtracted = 0 #won't happen unless do_register = True
use_denoised = 1 #use the deepcad denoised data, or just the caiman registered data
optex_setind = 'default' #specifies the extraction param set (set is created in configs.py, which uses map2opt.py to help create the param sets)

do_cropping_session = 0 #skip everything but FOV selection for all entries in rgname, must have already run motion correction if use_denoised=False, or motion correction and denoising if use_denoised=True, convenient to do for many recordings at once so extraction can be run on a batch of recordings in pth_allrecs without interruption


# caiman note on starting cluster
# The default backend mode for parallel processing is through the multiprocessing package.
# To make sure that this package is viewable from everywhere before starting the notebook
# these commands need to be executed from the terminal (in Linux and Windows):
# export MKL_NUM_THREADS=1
# export OPENBLAS_NUM_THREADS=1
use_cluster = 0 #leave as 0 because cluster isn't working (except on colab), and typical recordings (size 128 x 256 x 20 x 3000) don't take that long
cluster_backend = 'ipyparallel' #irrelevant if use_cluster=0

makeplots = 0 #plots were for old version of this pipeline,


print(sys.executable)
pth_env = sys.path

if (re.search("/Users/wienecke/", pth_env[0])):
  pth_allrec = '/Users/wienecke/~/ambrose/stacks/'
  if do_denoise: #need gpu, don't have one locally
     raise Exception("no gpu, make do_denoise false")
elif (re.search("/home/caw846/", pth_env[0])):
  pth_allrec = '/n/scratch3/users/c/caw846/stacks/'
  cluster_backend = 'SLURM' #this failed on O2, and so did cluster_backend = 'ipyparallel'
elif (re.search("/home/users/wienecke/", pth_env[0])):
  pth_allrec = '/scratch/users/wienecke/stacks/'
elif (re.search('/content', pth_env[0])):
  pth_allrec = '/content/drive/MyDrive/stacks/'
  use_cluster = 1 #cluster worked on colab
  optex_setind = 'default' #not set up for arguments in colab

pth_super = '/'.join(pth_allrec.split('/')[:-2])
pth_denoising = os.path.join(pth_super, 'denoising')
if not os.path.exists(pth_denoising):
    os.mkdir(pth_denoising)


if do_denoise and virtenv=='deepcad':
  print("forcing do_register and do_extract and use_cluster to zero because you're trying to denoise")
  do_register = 0
  do_extract = 0
  use_cluster = 0
  if denoise_volume==0 and len(denoise_slice_index)>1 and (denoise_slice_index != ['all'] or denoise_slice_index!='all'):
    raise Exception ("if denoise_volume==0, must either pass in single denoise_slice_index (not multiple), or denoise_slice_index must be all")
  if denoise_volume==1 and denoise_slice_index != ['all'] and denoise_slice_index!='all':
    raise Exception ("if denoise volume == 1, denoise slice index must be 'all' (for now, although code can be adapted to accept z subset range)")
elif (do_register or do_extract) and virtenv=='caiman':
  print("forcing do_denoise to zero because either do_register or do_extract is true")
  do_denoise = 0
else:
  raise Exception("virtenv is not set correctly")

[pth_readfile, fn_prefix, pth_prefix, pth_tif_reg_tmp, pth_tif_reg, pth_tif_dn, md] = \
  filefind(recdates, pth_allrec, fly, trial, jobind, do_background_subtraction,
        use_background_subtracted, do_register)



In [ ]:
#@title register

def register(pth_readfile, fn_prefix, pth_prefix, pth_tif_reg_tmp, pth_tif_reg, pth_denoising, md,
             do_background_subtraction, bg_patch_halfwidth, denoise_volume, cluster_backend, use_cluster, n_processes, dview):


    ##########################   BACKGROUND SUBTRACTION AND CAIMAN NORMCORRE MOTION CORRECTION   ##########################

    Y = imread(pth_readfile).astype('float32') ##having trouble on O2 with caiman function cm.load so just using imread from tifffile.tifffile

    Y = Y.reshape(md['dims'][0], md['dims'][1]+md['flyback'], md['dims'][2], md['dims'][3])

    if md['flyback']!=0:
        Y = Y[:,:-md['flyback'],:,:] #crop md['flyback'] frames

    #Y[540:600,4,:,:].play(magnification=2) #play in order t z y x
    Y = np.transpose(Y, (0, 3, 2, 1)) #put in order t x y z

    mnmv = np.min(Y)
    Y = Y - mnmv #make movie nonnegative (not sure this is necessary)
    print("MIN BEFORE MOTION CORRECTION " + str(mnmv))

    if do_background_subtraction:

        if Y.shape[3]==1: #if it's not volumetric
            zindall = [0]
        else:
            zindall = np.arange(Y.shape[3])

        for zind in zindall: #for every z slice

            dimorder = 'txy'
            pth_bgplot_save = pth_prefix + '_' + str(zind)
            br = bgremover(Y[:,:,:,zind], pth_bgplot_save, half_wid=bg_patch_halfwidth, dimorder=dimorder)
            br.draw_patches()
            br.remove_bg()
            br.make_plots()
            Y[:,:,:,zind] = np.transpose(br.out, (0, 2, 1))

        mnmv = np.min(Y)
        Y = Y - mnmv #make movie nonnegative (not sure this is necessary)
        print("MIN BEFORE MOTION CORRECTION AFTER BG SUB" + str(mnmv))

    imwrite(pth_tif_reg_tmp, Y.squeeze()) #write as t x y z (z might be singleton for non-volumetric data, so squeeze)

    min_mov = np.min(Y)
    opts_dict, indices_ex, fnadd = configs(optex_setind = 'default', fnames = pth_tif_reg_tmp, min_mov = min_mov, md = md) #configs for motion correction (will also define for extraction, but extraction params are in redefined later call to configs)
    opts = cnmf.params.CNMFParams(params_dict=opts_dict)

    #sys.setprofile(tracefunc)
    mc = cm.motion_correction.MotionCorrect([pth_tif_reg_tmp], dview=dview, **opts.get_group('motion'))
    mc.motion_correct(save_movie=True)
    os.remove(pth_tif_reg_tmp)

    border_to_0 = 0 if mc.border_nan == 'copy' else mc.border_to_0
    basename_memap = pth_tif_reg.split('/')[-1][:-4]
    pth_mmap_reg = cm.save_memmap(mc.mmap_file, base_name=basename_memap, order='C', border_to_0=border_to_0, dview=dview) # save in order C (motion_correct above has to save in order F)
    Y, dims_spatial_rg, dim_time_rg = cm.load_memmap(pth_mmap_reg)
    Y = np.reshape(Y.T, [dim_time_rg] + list(dims_spatial_rg), order='F')

    mnmv = np.min(Y)
    Y = Y - mnmv #make nonnegative before writing to uint16
    print("MIN AFTER MOTION CORRECTION " + str(mnmv))

    os.remove(mc.mmap_file[0]) #remove the mmap file in F order
    os.remove(pth_mmap_reg) #remove the mmap file in C order

    if md['dims'][1]==1:
        imwrite(pth_tif_reg, np.transpose(Y.astype('uint16'), (0, 2, 1)).reshape(dim_time_rg, dims_spatial_rg[1], dims_spatial_rg[0])) #write the registered movie as tif (uint16) for use in matlab, and caiman extraction below
    else:
        imwrite(pth_tif_reg, np.transpose(Y.astype('uint16'), (0, 3, 2, 1)).reshape(dim_time_rg * dims_spatial_rg[2], dims_spatial_rg[1], dims_spatial_rg[0])) #write the registered movie as tif (uint16) for use in matlab, and caiman extraction below


    # FINAL PART OF MOTION CORECTION SECTION  is to prepare files for denoising
    # by writing each z slice to separate tif and put them in separate folders
    # (since default in denoise.py is denoise_volume = 0 )
    # if using denoise_volume = 1, just move all separate tifs into one folder (might build this if clause)
    # (do this cpu-intensive part outside denoise.py, which is gpu-intensive, and called with different O2 resources)
    if int(fn_prefix.split('_')[0])>20230101: #if it's not my old project
        separate_z_slices_before_denoising(pth_tif_reg, fn_prefix, pth_denoising, md['dims'], denoise_volume)
    else:
        separate_z_slices_before_denoising_carls_old_project(pth_tif_reg, fn_prefix, pth_denoising, md['dims'], denoise_volume)



In [ ]:
#@title denoise

def denoise(pth_denoising, fn_prefix, dims, denoise_slice_index, denoise_volume):

    if int(fn_prefix.split('_')[0])>20230101: #if it's not my old grad school project
        carls_old_project = 0
        numstacks_all_refers_to = dims[1] # then 'all' is number of z slices (dims[1])
    else: #if it's my old grad project
        carls_old_project = 1
        if denoise_volume:
            pretend_trial = '1' # pretend they all come from same trial
            dnfolder = fn_prefix.split('_')[0] + '_' + fn_prefix.split('_')[1] + '_' + pretend_trial + '_all' #for these non-volumetric grad recordings, if do_volume == 1, rename all trials "1", and each trial a different z slice
            numstacks_all_refers_to = len(glob.glob(pth_denoising + '/' + dnfolder + '/*tif')) #and 'all' means all stacks in dnfolder (which is really all trials)
        else: #if not denoise_volume, all is just one stack
            numstacks_all_refers_to = 1

    print("all means this many stacks: ")
    print(numstacks_all_refers_to)

    print(pth_denoising)
    print(fn_prefix)
    print(dims)
    print(denoise_slice_index)
    print(denoise_volume)

    n_epochs = 5  # number of training epochs (loss is continuous across patches and epochs - epochs and patches are not independent)
    epochs_choose = [1, 2, 3, 4, 5] #list, one-indexed like n_epochs, which training epochs (which states of the model) to use for testing (denoising), for now choosing last and middle, and inspecting for overfit or underfit

    if denoise_volume:

        if carls_old_project:
            train_datasets_size = 13000
            patch_x = 120
            patch_y = 120
            patch_t = 200
            overlap_factor = 0.8
        else:
            train_datasets_size = 25000 #6000 #how many 3d xyt patches to train on, which is slightly different from what actually gets used
            patch_x = 120 # 110 #int(np.ceil(Lx/4)) #extent of patch in x
            patch_y = 120 #110 #int(np.ceil(Ly/4)) #extent of patch in y
            patch_t = 102 # 300 #extent of patch in t
            overlap_factor = 0.8 #0.9        # the overlap factor between two adjacent patches in x and y (t is more complicated see above)

    else:

        train_datasets_size = 6000
        patch_x = 110
        patch_y = 110
        patch_t = 102 #102 is about 20 sec for my framerate, may want to adjust for yours
        overlap_factor = 0.85

    select_img_num = 1e10 # number of frames to take from the beginning of each stack for training (make Lt or greater to use all frames)
    intensity_scale_factor = 1 # the factor for image intensity scaling
    num_frames_of_each_tif_to_denoise_for_visualization_during_training = 400 #for the optional inference visualization if save_test_images_per_epoch or visualize_images_per_epoch is True, and the code defaults to taking this number after the first 50 frames for display/save
    GPU = '0'                   # the index of GPU you will use (e.g. '0', '0,1', '0,1,2')
    num_workers = 0             # if you use Windows system, set this to 0.
    save_test_images_per_epoch = True  # whether to save result images after each epoch
    num_frames_of_each_tif_to_denoise = 1e10 #this is number of frames of each tif to be tested (denoised); make this the length of the stack (or greater) to get the whole stack denoised

    denoise_dtype = "uint16" #dtype for denoising, and writing results, but regardless, stitchdn will write to uint16


    if denoise_slice_index == ['all'] or denoise_slice_index=='all':
        zind_all_dn = np.arange(numstacks_all_refers_to)
    else:
        zind_all_dn = denoise_slice_index

    print(zind_all_dn)

    if denoise_volume: #if training on all slices , put them all in one folder
        pth_trainset_all = ['']
        pth_testset_all = ['']
    else: #if training on subset of slices, put each subset in separate folder (but right now subset must be single slice, which can be looped over if slice index is 'all')
        pth_trainset_all = ['']*len(zind_all_dn)
        pth_testset_all = ['']*len(zind_all_dn)

    countz = -1
    for zii in zind_all_dn: #deepcad wants 3d data, so organize slices into separate tif files, and put in one folder (if denoise_volume=1, ie train on all slices) or separate folders (if denoise_volume=0, ie train on z subset)

        if denoise_volume:
            dnfolder_insert = 'all'
            countz = 0 #constant 0 because every slice goes to the same directory
        else:
            dnfolder_insert = str(zii)
            countz = countz + 1

        dnfolder = fn_prefix + '_' + dnfolder_insert
        tifname = fn_prefix + '_' + str(zii) + '*_.tif'

        pth_trainset_all[countz] = pth_denoising + '/' + dnfolder #dir containing all tif files for training
        pth_testset_all[countz] = pth_trainset_all[countz] + '/' + dnfolder + '_*' #dir containing all models (.pth files) for test

        oldfldrs = glob.glob(pth_testset_all[countz]) #delete folders from old runs until you have resume training functionality written
        if oldfldrs:
            for ofi in oldfldrs:
                if os.path.isdir(ofi):
                    shutil.rmtree(ofi)

        print(pth_trainset_all[countz] + '/' + tifname)
        pth_tif_pdn = glob.glob(pth_trainset_all[countz] + '/' + tifname)
        print(pth_tif_pdn)
        for ofi in pth_tif_pdn: #these should be the same for all files
            Lt = int(ofi.split('/')[-1].split('_')[-5])
            Ly = int(ofi.split('/')[-1].split('_')[-4])
            Lx = int(ofi.split('/')[-1].split('_')[-3])
            denoise_input_dtype = ofi.split('/')[-1].split('_')[-2]

        denoise_input_shape = (Lt, Ly, Lx)
        print(denoise_input_shape)
        print(denoise_input_dtype)
        if denoise_input_dtype!=denoise_dtype:
            raise Exception("dtype doens't match intended")
        if denoise_input_shape != (dims[0], dims[2], dims[3]):
            raise Exception("dims changed")


    ########################### TRAIN ##########################

    for pth_trainset, pth_testset in zip(pth_trainset_all, pth_testset_all):

            print(pth_trainset)

            train_dict = {
                # dataset dependent parameters
                'patch_x': patch_x,                          # the width of 3D patches
                'patch_y': patch_y,                          # the height of 3D patches
                'patch_t': patch_t,                          # the time dimension (frames) of 3D patches
                'overlap_factor': overlap_factor,             # the factor for image intensity scaling
                'scale_factor': intensity_scale_factor,      # the factor for image intensity scaling
                'select_img_num': select_img_num, # number of images to take from the beginning of each stack (make larger than Lt use the full stack)
                'train_datasets_size': train_datasets_size,  # datasets size for training (how many 3D patches)
                'test_datasize': num_frames_of_each_tif_to_denoise_for_visualization_during_training,
                'datasets_path': pth_trainset,             # folder containing files for training
                'pth_dir': pth_trainset,                   # the path for pth file (saved models) and optional test images saved after each epoch if save_test_images_per_epoch=True

                # network related parameters
                'n_epochs': n_epochs,                          # the number of training epochs
                'lr': 0.00005,                                 # learning rate
                'b1': 0.5,                                     # Adam: beta1
                'b2': 0.9,                                   # Adam: beta2
                'fmap': 16,    # model complexity, 16 by default, deepcad author says it should not require adjustment
                'GPU': GPU,                                    # GPU index
                'num_workers': num_workers,                    # if you use Windows system, set this to 0.
                'visualize_images_per_epoch': False,                       # whether to show result images after each epoch
                'save_test_images_per_epoch': save_test_images_per_epoch,  # whether to save result images after each epoch
                'colab_display': True #if colab_display is true and save_test_images_per_epoch is false, it will error between training and testing
            }

            tc = training_class(train_dict)
            tc.run()


    ############################################# TEST (DENOISE) RECORDINGS WITH CHOSEN MODEL ##########################

            # deepcad defaults to denoising all tifs in datasets_path with all models (.pth files) in folder denoise_model
            # and will output denoised versions of those tifs and save in output_dir
            # but, to override default behavior, here i move all pth files except those listed in epochs_choose (which can still be all of them)

            pth_para = natsorted(glob.glob(pth_testset + '/' + '*.yaml'))[-1] #yaml file contains parameters used for training, to be loaded and reused for testing, since there is one yaml per folder, taking the last glob output takes the yaml in the most recent folder (the current run because of datetime in name)
            pth_pth_all = natsorted(glob.glob(pth_testset + '/' + '*.pth')) #paths to pth files (trained models, one for each epoch )

            pth_pth_keep_pattern = []
            for eci, epoch_choose in enumerate(epochs_choose):
                pth_pth_keep_pattern.append('E_' + "{:02d}".format(epoch_choose) + '_*.pth')

            pthcheck_prev = ''
            for ppi,pth_pth in enumerate(pth_pth_all): #make sure there aren't multiple train folders before you move pth files below
                pth_fldr_pth = '/'.join(pth_pth.split('/')[:-1])
                if ppi>0 and pth_fldr_pth != pthcheck_prev:
                    print(pthcheck_prev)
                    print(pth_fldr_pth)
                    raise Exception("multiple training folders, not allowed until resume training functionality exists")
                pthcheck_prev = pth_fldr_pth

            fldr_unused_pth = pth_fldr_pth + '/' + 'unused_pth_files/' #folder for the pth files you don't want to use for testing

            for pth_pth in pth_pth_all: #move all pth files besides the ones you want to test with
                fn_pth = pth_pth.split('/')[-1]
                if not any(fnmatch.fnmatch(fn_pth, pat+'*') for pat in pth_pth_keep_pattern):
                    if not os.path.exists(fldr_unused_pth):
                        os.mkdir(fldr_unused_pth)
                    shutil.move(pth_pth, fldr_unused_pth) #move all pth files besides the ones you want to test with

            fldr_pth = pth_fldr_pth.split('/')[-1] #folder with all the pth files



            with open(pth_para, "r") as stream: #read the params from training to apply to testing
                patch_t = train_dict['patch_t']
                patch_x = train_dict['patch_x']
                patch_y = train_dict['patch_y']
                fmap = train_dict['fmap']
                overlap_factor = train_dict['overlap_factor']

            test_dict = {
                # dataset dependent parameters
                'patch_x': patch_x,               # the width of 3D patches
                'patch_y': patch_y,               # the height of 3D patches
                'patch_t': patch_t,               # the time dimension (frames) of 3D patches
                'overlap_factor':overlap_factor,    # overlap factor
                'scale_factor': intensity_scale_factor, # the factor for image intensity scaling
                'test_datasize': num_frames_of_each_tif_to_denoise,     # the number of frames in each tif to be denoised/tested, measured from start
                'datasets_path': pth_trainset,     # folder containing all files to be tested
                'pth_dir': pth_trainset,                 # pth file root path
                'denoise_model' : fldr_pth,    # A folder containing all models (pth files) to be tested
                'output_dir' : pth_trainset,         # result file root path
                # network related parameters
                'fmap': fmap,                         # number of feature maps
                'GPU': GPU,                         # GPU index
                'num_workers': num_workers,         # if you use Windows system, set this to 0.
                'visualize_images_per_epoch': False, # whether to display inference performance after each epoch
                'save_test_images_per_epoch': save_test_images_per_epoch, # whether to save inference image after each epoch in pth path
                'colab_display': True #if colab_display is true and save_test_images_per_epoch is false, it will error between training and testing
            }

            tc = testing_class(test_dict)
            tc.run()


In [ ]:
#@title cluster

if use_cluster:
    if 'dview' in locals(): cm.stop_server(dview=dview)
    cc, dview, n_processes = cm.cluster.setup_cluster(backend='ipyparallel', n_processes=None, single_thread=False)
else:
  n_processes = 1 #set this in case you don't (or can't) setup cluster
  dview = None #set this in case you don't (or can't) setup cluster


In [ ]:
#@title run register or denoise


if do_register:
    register(pth_readfile, fn_prefix, pth_prefix, pth_tif_reg_tmp, pth_tif_reg, pth_denoising, md,
    do_background_subtraction, bg_patch_halfwidth, denoise_volume, cluster_backend, n_processes, dview)

if do_denoise:
    denoise(pth_denoising, fn_prefix, md['dims'], denoise_slice_index, denoise_volume)


In [ ]:
#@title plot denoised movie

if do_denoise:

  %matplotlib inline

  filename_add = 'f16'

  for pth_trainset, pth_testset in zip(pth_trainset_all, pth_testset_all):

    outtiff_path1 = natsorted(glob.glob(os.path.join(pth_trainset, '2023*', '*.tif')))

    for fnind, fn_display in enumerate(outtiff_path1):
      if fnind==3:
        print(fn_display)
        fntmp = fn_display.split('/')[-1].replace('.tif', '_output.tif')
        print(fntmp)
        outtiff_path2 = natsorted(glob.glob(os.path.join(pth_trainset, 'DataFolderIs_*', 'E_*', fntmp)))
        for fn_display2 in outtiff_path2:
          print(fn_display2)
          # display_length = 300
          # norm_min_percent = 0
          # norm_max_percent = 100
          # cropflag = 1
          # plot_denoised_movie(filename = fn_display2, filename_add = filename_add, cropflag=cropflag, display_length=display_length, norm_min_percent = norm_min_percent, norm_max_percent = norm_max_percent)

          # cropflag = 0
          # plot_denoised_movie(filename = fn_display, filename_add = filename_add, cropflag=cropflag, display_length=display_length, norm_min_percent = norm_min_percent, norm_max_percent = norm_max_percent)



In [ ]:
#@title load registered movie (if necessary) and create crop box for extraction

rgname = 'pb' #string not list of string (ie just do one region in ipynb bc loop is not really convenient in this notebook)
use_denoised = 1

if do_extract:

    if use_denoised:

        fn_dn_add = ''
        pth_tif_dn = pth_tif_dn + fn_dn_add
        epoch_choose = 2 #which epoch to stitch (must exist, ie must be one of epochs_choose in denoise.py)
        force_stitch = 0 #stitch regardless of whether the file already exists (e.g. to use a different run)
        if not os.path.isfile(pth_tif_dn) or force_stitch:
            if int(fn_prefix.split('_')[0])>20230101: #if it's not my old project
                stitchdn(pth_denoising, fn_prefix, pth_tif_dn, md['dims'], denoise_volume, epoch_choose) #stitch together denoised slices (tyx) into original size (tzyx)
            else:
                stitchdn_carls_old_project(pth_denoising, fn_prefix, pth_tif_dn, md['dims'], denoise_volume, epoch_choose) #stitch together denoised slices (tyx) into original size (tzyx)

        pth_exin = pth_tif_dn

    else:
        pth_exin = pth_tif_reg

    Y = imread(pth_exin).astype('float32')
    Y = Y.reshape(md['dims'])
    Y = np.transpose(Y, (0, 3, 2, 1)) #put in order t x y z
    print(Y.shape)

    create_croplim = 0

    try:

        fn_croplim_pattern = pth_prefix + '_' + rgname + '*_croplim_.npy' #find file matching fov subregion with some crop lim
        fn_croplim = glob.glob(fn_croplim_pattern)
        if len(fn_croplim) > 1:
            raise Exception("too many crop files")
        with open(fn_croplim[0], 'rb') as fnc:
            croplim = np.load(fnc)
        limits_str = str(croplim[0]) + '_' + str(croplim[1]) + '_' + str(croplim[2]) + '_' + str(croplim[3]) + '_' + str(croplim[4]) + '_' + str(croplim[5]) + '_' + str(croplim[6]) + '_' + str(croplim[7])

    except:

        if rgname == 'fullfov':

            croplim = np.asarray((1, dims[0], 1, dims[3], 1, dims[2], 1, dims[1])).astype(int)
            limits_str = '1_' + str(dims[0]) + '_1_' + str(dims[3]) + '_1_' + str(dims[2]) + '_1_' + str(dims[1])
            fn_crop_lim = pth_prefix + '_' + rgname + '_' + limits_str + '_croplim_.npy'
            with open(fn_crop_lim, 'wb') as fncrop:
                np.save(fncrop, croplim)

        else:

            print("crop fov for " + rgname)
            create_croplim = 1
            Ymt = np.mean(Y, axis = 0)
            if Ymt.shape[-1]==1: #only do z slice selection if the movie is volumetric 4d
              zlimits = (1,1)
              Ymtz = np.mean(Ymt, axis = 2)
            else:
              zlimits = select_fov_z(Ymt)
              Ymtz = np.mean(Ymt[:,:,zlimits[0]-1:zlimits[1]-1], axis = 2)
            fn_crop_lim_xy = pth_prefix + '_' + rgname + '_' + 'croplimxytmp_.npy'
            draw_rect_xy(Ymtz, fn_crop_lim_xy)



In [ ]:
#@title crop fov for extraction

if do_extract:  #had to put this here (in new cell) to get interactive plots to work in above cell

  if create_croplim:

    with open(fn_crop_lim_xy, 'rb') as fnc:
      croplimxy = np.load(fnc)
    ylimits = (croplimxy[0], croplimxy[1])
    xlimits = (croplimxy[2], croplimxy[3])
    tlimits = (1, md['dims'][0])
    croplim = np.asarray((tlimits + xlimits + ylimits + zlimits)).astype(int) #make them 1-indexed for matlab later
    limits_str = str(croplim[0]) + '_' + str(croplim[1]) + '_' + str(croplim[2]) + '_' + str(croplim[3]) + '_' + str(croplim[4]) + '_' + str(croplim[5]) + '_' + str(croplim[6]) + '_' + str(croplim[7])
    fn_crop_lim = pth_prefix + '_' + rgname + '_' + limits_str + '_croplim_.npy'
    with open(fn_crop_lim, 'wb') as fncrop:
        np.save(fncrop, croplim)

  slt = slice(croplim[0]-1, croplim[1], 1) #croplim are 1-indexed, and the second/upper is not included
  slx = slice(croplim[2]-1, croplim[3], 1)
  sly = slice(croplim[4]-1, croplim[5], 1)
  slz = slice(croplim[6]-1, croplim[7], 1)
  indices_crop = [slt, slx, sly, slz]
  Ycrop = Y[tuple(indices_crop)]
  Y = None




In [ ]:
#@title start cluster

if use_cluster:

    if 'dview' in locals(): cm.stop_server(dview=dview)
    cc, dview, n_processes = cm.cluster.setup_cluster(backend='ipyparallel', n_processes=None, single_thread=False)

In [ ]:
#@title memmap and load movie for extraction

if do_extract:

  pth_tif_ex = pth_exin[:-4] + rgname + '_' + limits_str + '_cmex_tmp_.tif'
  imwrite(pth_tif_ex, Ycrop.squeeze()) #squeeze in case 3d . . . also must imwrite it to memmap it, and must memmap it to use patches in extraction
  basename_memap = pth_tif_ex.split('/')[-1][:-4]
  border_to_0 = 0 #if mc.border_nan == 'copy' else mc.border_to_0
  fn_mmap_ex = cm.save_memmap([pth_tif_ex], base_name=basename_memap, order='C', border_to_0=border_to_0, dview=dview) # exclude borders
  os.remove(pth_tif_ex)
  Ycrop, dims_spatial_ex, dim_time_ex = cm.load_memmap(fn_mmap_ex) #if 3d mmap should be 3d, but Ycrop gets singleton 4th dim (z) added below so the code is more readable
  Ycrop = np.reshape(Ycrop.T, [dim_time_ex] + list(dims_spatial_ex), order='F')

  if len(Ycrop.shape)==3: #if it's not volumetric
      Ycrop = Ycrop[...,np.newaxis] #add singleton 4th dim (z) so the code is more readable

  print(Ycrop.shape)


In [ ]:
#@title extract

optex_setind = -3#'default' #0 #redefined here in notebook (originally defined in "choose files" cell, but that's far away and we're not looping in notebook)

if do_extract:

    if optex_setind == 'default':
        optex_setind_new = ['default'] #make it iterable with brackets
    elif optex_setind<0: #if negative, initiate loop over extraction params here, range [0 - optex_setind]
        manual_start_ind = 0
        optex_setind_new = np.arange(manual_start_ind, -optex_setind)
    else: #if positive, just the one extraction param whose index matches optex_setind
        optex_setind_new = [optex_setind]

    print("optex_setind NEW " + str(optex_setind_new))

    for ii in optex_setind_new:

        try: #try, since some param sets will error

          opts_dict, indices_ex, fnadd = configs(optex_setind = ii, fnames = fn_mmap_ex, md = md, extract_in_2d = extract_in_2d, dims_spatial_ex = dims_spatial_ex) #param set for extraction
          opts = cnmf.params.CNMFParams(params_dict=opts_dict)

          if extract_in_2d: #adjust images and some params for planar
              sliceindz = np.arange(Ycrop.shape[3])
              dims_roimask_spatial = (dims_spatial_ex[0], dims_spatial_ex[1])
          else:
              sliceindz = [np.arange(Ycrop.shape[3])] #all slices in one list (not planar)
              dims_roimask_spatial = (dims_spatial_ex[0], dims_spatial_ex[1], dims_spatial_ex[2])

          countz = 0
          for si in sliceindz: #for each slice (or all slices if extract_in_2d = false)

              cnm = None
              cnm2 = None

              if extract_in_2d:
                  print("PLANAR EXTRACTION FOR SLICE " + str(si))
                  images_sliced = Ycrop[:,:,:,si]
              else:
                  print("3D EXTRACTION FOR ALL SLICES")
                  images_sliced = Ycrop #can't .copy() for some reason, for 3d extraction keep all images for loop over ii

              cnm = cnmf.CNMF(n_processes, params=opts, dview=dview)
              cnm = cnm.fit(images_sliced, indices = indices_ex)

              cnm.estimates.evaluate_components(images_sliced, cnm.params, dview=dview)
              print(('NUMGOOD ' + str(len(cnm.estimates.idx_components)) + ' NUMBAD ' + str(len(cnm.estimates.idx_components_bad))))

              cnm.estimates.select_components(use_object=True, save_discarded_components=False)

              ######################  REFIT  ############################
              cnm2 = cnm.refit(images_sliced)

              cnm2.estimates.evaluate_components(images_sliced, cnm2.params, dview=dview)
              print(('REFIT: NUMGOOD ' + str(len(cnm2.estimates.idx_components)) + ' NUMBAD ' + str(len(cnm2.estimates.idx_components_bad))))

              cnm2.estimates.detrend_df_f(detrend_only=False, flag_auto=True, use_residuals=False) #use_residuals=False to not include residuals in traces for dff computation (default)
              dff_residfalse = cnm2.estimates.F_dff
              cnm2.estimates.detrend_df_f(detrend_only=False, flag_auto=True, use_residuals=True) #use_residuals=True to include residuals in traces for dff computation
              dff_residtrue = cnm2.estimates.F_dff
              cnm2.estimates.select_components(use_object=True, save_discarded_components=False)


              if countz==0:

                  numroi_stack_pad = cnm2.estimates.A.shape[-1]
                  dims_roimask_stack = ( dims_roimask_spatial + (numroi_stack_pad, ) )
                  dims_roimask_b_stack = ( dims_roimask_spatial + (cnm2.estimates.b.shape[-1], ) )
                  dims_timeseries_stack = ( numroi_stack_pad, cnm2.estimates.C.shape[1] )

                  cma = np.zeros(dims_roimask_stack + (len(sliceindz), ) )
                  cmb = np.zeros(dims_roimask_b_stack + (len(sliceindz), ) )
                  cmc = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
                  # cmyra = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
                  cms = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
                  cmdff = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
                  # cmdffr = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
                  cmsnr = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )
                  cmrval = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )
                  # stack_idx = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )
                  # stack_idx_bad = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )

              numroi_slice = cnm2.estimates.A.shape[-1]
              numroi_b_slice = cnm2.estimates.b.shape[-1]
              dims_mask_slice = (dims_roimask_spatial + (numroi_slice, ) )
              dims_mask_b_slice = (dims_roimask_spatial + (numroi_b_slice, ) )

              cma[..., :numroi_slice, countz] = np.reshape(cnm2.estimates.A.toarray(), dims_mask_slice, order='F')
              cmb[..., :numroi_b_slice, countz] = np.reshape(cnm2.estimates.b, dims_mask_b_slice, order='F')
              cmc[:numroi_slice,:,countz] = cnm2.estimates.C
              # cmyra[:numroi_slice,:,countz] = cnm2.estimates.YrA
              cms[:numroi_slice,:,countz] = cnm2.estimates.S
              cmdff[:numroi_slice,:,countz] = dff_residfalse
              # cmdffr[:numroi_slice,:,countz] = dff_residtrue
              cmsnr[:numroi_slice,countz] = cnm2.estimates.SNR_comp
              cmrval[:numroi_slice,countz] = cnm2.estimates.r_values
              #stack_idx[:cnm2.estimates.idx_components.shape[0],countz] = cnm2.estimates.idx_components
              #if cnm2.estimates.idx_components_bad.shape==(1,):
              #    stack_idx_bad[:cnm2.estimates.idx_components_bad.shape[0],countz] = cnm2.estimates.idx_components_bad

              countz = countz + 1

          log_files = glob.glob('*_LOG_*')
          for log_file in log_files:
              os.remove(log_file)

          mdict = {}
          mdict['roimasks'] = cma.astype('float32')
          mdict['roimasks_b'] = cmb.astype('float32')
          mdict['C'] = cmc.astype('float32')
          # mdict['YrA'] = cmyra.astype('float32')
          mdict['S'] = cms.astype('float32')
          mdict['dff'] = cmdff.astype('float32')
          # mdict['dffr'] = cmdffr.astype('float32')
          mdict['snr'] = cmsnr.astype('float32')
          mdict['rval'] = cmrval.astype('float32')
          #mdict['idx'] = stack_idx
          #mdict['idxbad'] = stack_idx_bad

          if np.any(cma):
            pth_mat_ex = pth_tif_ex[:-8] + fnadd + '_rois_.mat'
          else:
            mdict = {}
            print("norois")
            pth_mat_ex = pth_tif_ex[:-8] + fnadd + '_rois_NOROIS_.mat'

        except Exception as error:

            mdict = {}
            pth_mat_ex = pth_tif_ex[:-8] + fnadd + '_rois_FAILURE_.mat'
            print("An exception occurred:", type(error).__name__, "-", error)


        sio.savemat(pth_mat_ex, mdict)

        if dview is not None: cm.stop_server(dview=dview)




In [ ]:
#@title plot rois

#cnm.estimates.nb_view_components_3d(image_type='corr', dims=dims_spatial_ex, Yr=images_sliced, denoised_color='red', max_projection=True);
#cnm.estimates.nb_view_components_3d(image_type='mean', axis = 2, dims=dims_spatial_ex, Yr=None, denoised_color='red', max_projection=False);
#cnm2.estimates.nb_view_components_3d(image_type='corr', dims=dims_spatial_ex, Yr=images_sliced, denoised_color='red', max_projection=True);
cnm2.estimates.nb_view_components_3d(image_type='mean', axis = 2, dims=dims_spatial_ex, Yr=None, denoised_color='red', max_projection=False);

# cnm2.estimates.SNR_comp
# cnm2.estimates.r_values

In [ ]:
#@title plot responses and residuals

# indies = np.arange(1,600)
# # plt.plot(cnm2.estimates.C[1,indies])

# # plt.plot(cnm2.estimates.R[1,indies])
# # plt.plot(dff_residfalse[1,indies])
# # plt.plot(dff_residtrue[1,indies])

# data1 = cnm2.estimates.C[0,indies]
# data2 = cnm2.estimates.R[0,indies]
# data3 = data1+data2
# data4 = dff_residfalse[0,indies]
# data5 = dff_residtrue[0,indies]
# t = indies

# fig, ax1 = plt.subplots()

# color1 = 'tab:blue'
# color2 = 'tab:red'
# color3 = 'tab:pink'
# color4 = 'tab:green'
# color5 = 'tab:purple'
# ax1.set_xlabel('time (s)')
# ax1.set_ylabel('exp', color='black')
# #ax1.plot(t, data1, color=color1)
# #ax1.plot(t, data2, color=color2)
# ax1.plot(t, data3, color=color3)
# ax1.tick_params(axis='y', labelcolor='black')
# ylim1 = ax1.get_ylim()

# ax2 = ax1.twinx()  # instantiate a second axes that shares the same x-axis

# ax2.set_ylabel('sin', color='black')  # we already handled the x-label with ax1
# #ax2.plot(t, data4, color=color4)
# #ax2.plot(t, data5, color=color5)
# ax2.tick_params(axis='y', labelcolor='black')
# #ax2.set_ylim([ylim1[0], ylim1[1]])

# fig.tight_layout()  # otherwise the right y-label is slightly clipped
# plt.show()






In [ ]:
#@title extract again (now integrated above)

# if do_extraction:

#   try:

#     cnm2 = cnm.refit(images_sliced)

#     cnm2.estimates.evaluate_components(images_sliced, cnm2.params, dview=dview)
#     print(('REFIT: NUMGOOD ' + str(len(cnm2.estimates.idx_components)) + ' NUMBAD ' + str(len(cnm2.estimates.idx_components_bad))))

#     cnm2.estimates.detrend_df_f(detrend_only=False, flag_auto=True, use_residuals=False) #use_residuals=False to not include residuals in traces for dff computation (default)
#     dff_residfalse = cnm2.estimates.F_dff
#     cnm2.estimates.detrend_df_f(detrend_only=False, flag_auto=True, use_residuals=True) #use_residuals=True to include residuals in traces for dff computation
#     dff_residtrue = cnm2.estimates.F_dff
#     cnm2.estimates.select_components(use_object=True, save_discarded_components=False)

#   except:

#     mdict = {}
#     pth_mat_ex = [pth_tif_ex[:-8] + fnadd + '_rois_FAILURE_.mat']


In [ ]:
#@title plots (now integrated above)

# if do_extraction:

#   if extract_in_2d:

#       Cn = cm.local_correlations(images_sliced.transpose(1,2,0))
#       Cn[np.isnan(Cn)] = 0
#       print('you may need to change the data rate to generate nb_view_components: use jupyter notebook --NotebookApp.iopub_data_rate_limit=1.0e10 before opening jupyter notebook')

#       cnm.estimates.plot_contours_nb(img=Cn) #img=None for mean projection

#       cnm2.estimates.plot_contours_nb(img=Cn, idx=cnm2.estimates.idx_components)

#       cnm2.estimates.nb_view_components(img=Cn, idx=cnm2.estimates.idx_components)

#       if len(cnm2.estimates.idx_components_bad) > 0:
#         cnm2.estimates.nb_view_components(img=Cn, idx=cnm2.estimates.idx_components_bad)
#       else:
#         print("No components were rejected.")

#       cnm.estimates.play_movie(images_sliced, q_max=99.9, gain_res=2, magnification=2, bpx=True, include_bck=False, save_movie=True)

#       A2 = cnm.estimates.A.toarray().reshape(opts.data['dims'] + (-1,), order='F').transpose([2, 0, 1])
#       Nc = A2.shape[0]
#       grid_shape = (np.ceil(np.sqrt(Nc/2)).astype(int), np.ceil(np.sqrt(Nc*2)).astype(int))
#       plt.figure(figsize=np.array(grid_shape[::-1])*1.5)
#       plt.imshow(montage(A2, rescale_intensity=True, grid_shape=grid_shape))
#       plt.axis('off')

#   else:

#       cnm.estimates.nb_view_components_3d(image_type='mean', dims_spatial=dims_spatial_ex, axis=2)



In [ ]:
#@title save (now integrated above)

# if do_extraction:

#   if countz==0: #THIS IS POINTLESS WITHOUT THE LOOP, COUNTZ IS ALWAYS 0 (NO LOOP IN IPYNB CURRENTLY)

#           padnum = 0
#           padnum_b = 0
#           numroi_stack_pad = cnm2.estimates.A.shape[-1] + padnum #extra since it can vary a little across fits (even above input k)
#           dims_roimask_stack = ( dims_roimask_spatial + (numroi_stack_pad, ) )
#           dims_roimask_b_stack = ( dims_roimask_spatial + (cnm2.estimates.b.shape[-1] + padnum_b, ) )
#           dims_timeseries_stack = ( numroi_stack_pad, cnm2.estimates.C.shape[1] )

#           cma = np.zeros(dims_roimask_stack + (len(sliceindz), ) )
#           cmb = np.zeros(dims_roimask_b_stack + (len(sliceindz), ) )
#           cmc = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
#           # cmyra = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
#           cms = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
#           cmdff = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
#           # cmdffr = np.zeros(dims_timeseries_stack + (len(sliceindz), ) )
#           cmsnr = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )
#           cmrval = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )
#           # stack_idx = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )
#           # stack_idx_bad = np.zeros((dims_timeseries_stack[0], ) + (len(sliceindz), ) )

#       numroi_slice = cnm2.estimates.A.shape[-1]
#       numroi_b_slice = cnm2.estimates.b.shape[-1]
#       dims_mask_slice = (dims_roimask_spatial + (numroi_slice, ) )
#       dims_mask_b_slice = (dims_roimask_spatial + (numroi_b_slice, ) )

#       cma[..., :numroi_slice, countz] = np.reshape(cnm2.estimates.A.toarray(), dims_mask_slice, order='F')
#       cmb[..., :numroi_b_slice, countz] = np.reshape(cnm2.estimates.b, dims_mask_b_slice, order='F')
#       cmc[:numroi_slice,:,countz] = cnm2.estimates.C
#       # cmyra[:numroi_slice,:,countz] = cnm2.estimates.YrA
#       cms[:numroi_slice,:,countz] = cnm2.estimates.S
#       cmdff[:numroi_slice,:,countz] = dff_residfalse
#       # cmdffr[:numroi_slice,:,countz] = dff_residtrue
#       cmsnr[:numroi_slice,countz] = cnm2.estimates.SNR_comp
#       cmrval[:numroi_slice,countz] = cnm2.estimates.r_values
#       #stack_idx[:cnm2.estimates.idx_components.shape[0],countz] = cnm2.estimates.idx_components
#       #if cnm2.estimates.idx_components_bad.shape==(1,):
#       #    stack_idx_bad[:cnm2.estimates.idx_components_bad.shape[0],countz] = cnm2.estimates.idx_components_bad

#       countz = countz + 1

#   log_files = glob.glob('*_LOG_*')
#   for log_file in log_files:
#       os.remove(log_file)

#   mdict = {}
#   mdict['roimasks'] = cma.astype('float32')
#   mdict['roimasks_b'] = cmb.astype('float32')
#   mdict['C'] = cmc.astype('float32')
#   # mdict['YrA'] = cmyra.astype('float32')
#   mdict['S'] = cms.astype('float32')
#   mdict['dff'] = cmdff.astype('float32')
#   # mdict['dffr'] = cmdffr.astype('float32')
#   mdict['snr'] = cmsnr.astype('float32')
#   mdict['rval'] = cmrval.astype('float32')
#   #mdict['idx'] = stack_idx
#   #mdict['idxbad'] = stack_idx_bad

#   if np.any(cma):
#       pth_mat_ex = pth_tif_ex[:-8] + fnadd + '_rois_.mat'
#   else:
#       mdict = {}
#       print("norois")
#       pth_mat_ex = pth_tif_ex[:-8] + fnadd + '_rois_NOROIS_.mat'

#   sio.savemat(pth_mat_ex, mdict)

#   if dview is not None: cm.stop_server(dview=dview)